## Open notebook in:
| Colab                                 
:-------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------------|
[![Open In Colab](https://colab.research.google.com/assets/colab-badge.svg)](https://colab.research.google.com/github/Nicolepcx/transformers-the-definitive-guide/blob/master/CH06/ch06_music_generation.ipynb)                                             

# About this Notebook

This notebook explores **music generation** using Meta's `MusicGen` models from the `transformers` library. It demonstrates how to generate new musical content both **from text prompts** and by **conditioning on existing audio files**, enabling controlled, multi-modal music creation. The workflow integrates pre-trained models like `musicgen-small` and `musicgen-large`, and shows how to modify inputs such as genre, tempo, and instrumentation through text conditioning.

### Steps Included:

1. **Repository Setup and Asset Loading**:
   The notebook begins by cloning Meta’s `audiocraft` repository and listing included audio assets. These assets serve as optional input references for audio-conditioned generation.

2. **Model Loading and Initialization**:
   Pre-trained `MusicgenForConditionalGeneration` models (`musicgen-large` and `musicgen-small`) are loaded. The device configuration is automatically handled to leverage GPU acceleration if available.

3. **Unconditional Music Generation**:
   Using `get_unconditional_inputs`, the notebook demonstrates how to sample random musical content without any conditioning input, showing the model's capacity to generate music from scratch.

4. **Text-to-Music Generation**:
   A set of genre-based prompts (e.g., classical, EDM, minimal) are passed to the model to generate music aligned with the provided textual description. Generated waveforms are normalized, saved as `.wav` files, and optionally played inline.

5. **Audio-Conditioned Generation**:
   Local audio files (e.g., loops, full music tracks) are loaded and resampled to 32 kHz as expected by MusicGen. The audio is paired with textual prompts (e.g., “Hip hop with nuances of soul and funk”) to guide the model in generating stylistically similar or enhanced content.

6. **Resampling and Preprocessing**:
   The notebook includes examples of converting stereo to mono, slicing to specific durations, and resampling to match the model’s input expectations, using `torchaudio` and `scipy`.

7. **Output Formatting and Playback**:
   Generated outputs are normalized, converted to 16-bit PCM `.wav` files, and played directly within the notebook. This facilitates rapid evaluation of stylistic fidelity, audio quality, and genre alignment.

This notebook highlights the capabilities of **multi-modal music generation**, where structured prompts or example tracks can serve as creative seeds for generating high-quality music. It's useful for artists, researchers, and engineers exploring generative audio, music production automation, or AI-assisted composition tools.


# Clone the audiocraft repository

In [ ]:

!git clone https://github.com/facebookresearch/audiocraft.git

#List files in the 'assets' folder
import os

asset_folder = "audiocraft/assets"
print(f"Listing contents of {asset_folder}:\n")
for file_name in os.listdir(asset_folder):
    print(file_name)


fatal: destination path 'audiocraft' already exists and is not an empty directory.
Listing contents of audiocraft/assets:

chord_to_index_mapping.pkl
bach.mp3
electronic.mp3
CJ_Beatbox_Loop_05_90.wav
salience_1.wav
salience_2.wav
salience_1.th
bolero_ravel.mp3
epic.wav
sirens_and_a_humming_engine_approach_and_pass.mp3
sep_drums_1.mp3
salience_2.th
a_duck_quacking_as_birds_chirp_and_a_pigeon_cooing.mp3


# Installs

In [ ]:
!pip install transformers==4.53.1 gdown -qqq

     ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 40.9/40.9 kB 2.5 MB/s eta 0:00:00
   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 10.8/10.8 MB 50.0 MB/s eta 0:00:00
   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 566.4/566.4 kB 20.5 MB/s eta 0:00:00
   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 3.1/3.1 MB 50.7 MB/s eta 0:00:00


# Imports

In [ ]:
import numpy as np
import torch
from IPython.display import Audio, display
from scipy.io.wavfile import write as write_wav
import torchaudio
from torchaudio.transforms import Resample
from transformers import AutoProcessor, MusicgenForConditionalGeneration



# Display Available Audio Assets

Iterates over files in the asset folder and plays any audio files with `.wav` or `.mp3` extensions for inspection.



In [ ]:
# Display all playable audio files
for file_name in os.listdir(asset_folder):
    if file_name.endswith((".wav", ".mp3")):
        print(f"Playing: {file_name}")
        display(Audio(os.path.join(asset_folder, file_name)))


Playing: bach.mp3


Playing: electronic.mp3


Playing: CJ_Beatbox_Loop_05_90.wav


Playing: salience_1.wav


Playing: salience_2.wav


Playing: bolero_ravel.mp3


Playing: epic.wav


Playing: sirens_and_a_humming_engine_approach_and_pass.mp3


Playing: sep_drums_1.mp3


Playing: a_duck_quacking_as_birds_chirp_and_a_pigeon_cooing.mp3


# Load MusicGen Model and Generate Unconditional Audio

Initializes the `musicgen-large` model and generates an unconditional audio sample using the default latent noise.


In [ ]:
model = MusicgenForConditionalGeneration.from_pretrained("facebook/musicgen-small")

/usr/local/lib/python3.12/dist-packages/huggingface_hub/utils/_auth.py:104: UserWarning: 
Error while fetching `HF_TOKEN` secret value from your vault: 'Requesting secret HF_TOKEN timed out. Secrets can only be fetched when running from the Colab UI.'.
You are not authenticated with the Hugging Face Hub in this notebook.
If the error persists, please let us know by opening an issue on GitHub (https://github.com/huggingface/huggingface_hub/issues/new).
  warnings.warn(


config.json: 0.00B [00:00, ?B/s]

model.safetensors:   0%|          | 0.00/2.36G [00:00<?, ?B/s]

generation_config.json:   0%|          | 0.00/224 [00:00<?, ?B/s]

In [ ]:
device = "cuda:0" if torch.cuda.is_available() else "cpu"
model.to(device)

MusicgenForConditionalGeneration(
  (text_encoder): T5EncoderModel(
    (shared): Embedding(32128, 768)
    (encoder): T5Stack(
      (embed_tokens): Embedding(32128, 768)
      (block): ModuleList(
        (0): T5Block(
          (layer): ModuleList(
            (0): T5LayerSelfAttention(
              (SelfAttention): T5Attention(
                (q): Linear(in_features=768, out_features=768, bias=False)
                (k): Linear(in_features=768, out_features=768, bias=False)
                (v): Linear(in_features=768, out_features=768, bias=False)
                (o): Linear(in_features=768, out_features=768, bias=False)
                (relative_attention_bias): Embedding(32, 12)
              )
              (layer_norm): T5LayerNorm()
              (dropout): Dropout(p=0.1, inplace=False)
            )
            (1): T5LayerFF(
              (DenseReluDense): T5DenseActDense(
                (wi): Linear(in_features=768, out_features=3072, bias=False)
                (wo): L

# Inspect Sampling Rate and Estimate Audio Duration

Retrieves the sampling rate and computes the expected duration of generated audio based on the frame rate and token count.


In [ ]:
unconditional_inputs = model.get_unconditional_inputs(num_samples=1)

audio_values = model.generate(**unconditional_inputs, do_sample=True, max_new_tokens=256)

sampling_rate = model.config.audio_encoder.sampling_rate
Audio(audio_values[0].cpu().numpy(), rate=sampling_rate)

print(sampling_rate)

32000


In [ ]:
audio_length_in_s = 256 / model.config.audio_encoder.frame_rate

audio_length_in_s

5.12

# Prompt-Based Music Generation by Genre

Uses predefined textual prompts (e.g., "classical piano music", "EDM hardcore Techno sound") to generate genre-specific audio and saves the output as `.wav` files.


In [ ]:
processor = AutoProcessor.from_pretrained("facebook/musicgen-small")

# Define genres and prompts
genre_prompts = {
    "classical": "classical piano music",
    "minimal": "minimal house rather monoton in rhythm",
    "EDM": "EDM hardcore Techno sound",
}

# Generate and save each audio
for genre, prompt in genre_prompts.items():
    # Prepare input
    inputs = processor(text=[prompt], padding=True, return_tensors="pt").to(device)

    # Generate audio
    audio_values = model.generate(
        **inputs,
        do_sample=True,
        guidance_scale=3,
        max_new_tokens=1024
    )

    # Convert to numpy and clip
    audio_np = audio_values[0].cpu().numpy().squeeze()
    audio_np = np.clip(audio_np, -1.0, 1.0)
    audio_int16 = (audio_np * 32767).astype(np.int16)

    # Save as WAV
    filename = f"{genre}.wav"
    write_wav(filename, sampling_rate, audio_int16)

    # Optionally play back
    display(Audio(audio_np, rate=sampling_rate))


preprocessor_config.json:   0%|          | 0.00/275 [00:00<?, ?B/s]

tokenizer_config.json: 0.00B [00:00, ?B/s]

spiece.model:   0%|          | 0.00/792k [00:00<?, ?B/s]

tokenizer.json: 0.00B [00:00, ?B/s]

special_tokens_map.json: 0.00B [00:00, ?B/s]

# Audio-Conditioned Music Generation from Beatbox Loop

Loads a local `.wav` file, preprocesses it (mono conversion, resampling, truncation), and uses it along with a text prompt to generate music via `musicgen-small`.


In [ ]:

# Load and resample the local audio file
file_path = "audiocraft/assets/CJ_Beatbox_Loop_05_90.wav"
waveform, orig_sr = torchaudio.load(file_path)

# Convert to mono
if waveform.shape[0] > 1:
    waveform = waveform.mean(dim=0, keepdim=True)

# Resample to 32 kHz
target_sr = 32000
if orig_sr != target_sr:
    resampler = Resample(orig_freq=orig_sr, new_freq=target_sr)
    waveform = resampler(waveform)

waveform_np = waveform.squeeze().numpy()

# Optional: Use only first 4 seconds
waveform_np = waveform_np[:target_sr * 4]

# Step 4: Load model and processor
processor = AutoProcessor.from_pretrained("facebook/musicgen-small")
model = MusicgenForConditionalGeneration.from_pretrained("facebook/musicgen-small")

# Step 5: Prepare input
inputs = processor(
    audio=waveform_np,
    sampling_rate=target_sr,
    text=["Hip hop with nuances of soul and funk"],
    padding=True,
    return_tensors="pt",
)

# Step 6: Generate music
audio_values = model.generate(
    **inputs,
    do_sample=True,
    guidance_scale=3.0,
    max_new_tokens=512
)

# Step 7: Convert and save output
output = audio_values[0].numpy()
output = output / np.max(np.abs(output))  # Normalize

output = audio_values[0].numpy()

# Normalize to [-1, 1]
output = output / np.max(np.abs(output) + 1e-8)

# Convert to 16-bit PCM
output_int16 = (output * 32767).astype(np.int16)

# Make sure it's 1D
if output_int16.ndim > 1:
    output_int16 = output_int16.squeeze()

# Write with proper casting of sample rate
write_wav("hiphop_generated.wav", int(target_sr), output_int16)

# Play back
from IPython.display import Audio, display
display(Audio("hiphop_generated.wav"))


# Audio-Conditioned Music Generation from Classical Track

Processes a classical `.mp3` file (e.g., Ravel's *Boléro*), prepares it for input, and generates music conditioned on both the waveform and a descriptive prompt using `musicgen-large`.


In [ ]:

# Step 3: Load and resample the local audio file
file_path = "audiocraft/assets/bolero_ravel.mp3"
waveform, orig_sr = torchaudio.load(file_path)

# Convert to mono
if waveform.shape[0] > 1:
    waveform = waveform.mean(dim=0, keepdim=True)

# Resample to 32 kHz
target_sr = 32000
if orig_sr != target_sr:
    resampler = Resample(orig_freq=orig_sr, new_freq=target_sr)
    waveform = resampler(waveform)

waveform_np = waveform.squeeze().numpy()

# Optional: Use only first 4 seconds
#waveform_np = waveform_np[:target_sr * 4]

# Step 4: Load model and processor
processor = AutoProcessor.from_pretrained("facebook/musicgen-small")
model = MusicgenForConditionalGeneration.from_pretrained("facebook/musicgen-small")

# Step 5: Prepare input
inputs = processor(
    audio=waveform_np,
    sampling_rate=target_sr,
    text=["classical piano music"],
    padding=True,
    return_tensors="pt",
)

# Step 6: Generate music
audio_values = model.generate(
    **inputs,
    do_sample=True,
    guidance_scale=3.0,
    max_new_tokens=512
)

# Step 7: Convert and save output
output = audio_values[0].numpy()
output = output / np.max(np.abs(output))  # Normalize

output = audio_values[0].numpy()

# Normalize to [-1, 1]
output = output / np.max(np.abs(output) + 1e-8)

# Convert to 16-bit PCM
output_int16 = (output * 32767).astype(np.int16)

# Make sure it's 1D
if output_int16.ndim > 1:
    output_int16 = output_int16.squeeze()

# Write with proper casting of sample rate
write_wav("hiphop_generated.wav", int(target_sr), output_int16)

# Play back
display(Audio("hiphop_generated.wav"))
